<style>
body,
.jp-RenderedHTMLCommon {
  font-size: 8px !important;
  line-height: 1 !important;
}

.jp-RenderedHTMLCommon h1,
.jp-RenderedHTMLCommon h2,
.jp-RenderedHTMLCommon h3 {
  break-after: avoid-page;
  page-break-after: avoid;
}
</style>

# NFL Fantasy Football Analytics: Evaluating Fantasy Football Player & Team Statistics 

Prepared 10.3.2026
SIADS 593: Milestone 1 

This report uses NFL player statistics from 2018–2025 to identify what drives fantasy football scoring and how that knowledge can improve drafting decisions. It examines which statistics correlate most strongly with fantasy points, how positional value differs between PPR and non-PPR formats, and which positions should be prioritized in a standard 12-team draft. It then identifies the general traits that distinguish strong QBs, RBs, WRs, and TEs. The goal is a data-driven strategic framework for building a fantasy team. It is built on position-level trends rather than individual player recommendations.

**Disclaimer:** This analysis is intended for educational purposes only. It is not betting, wagering, or financial advice, and it should not be used to place bets or to guide gambling decisions of any kind. The findings describe historical trends and do not predict or guarantee future player or team performance. Gambling can be harmful and addictive. If you or someone you know is struggling with problem gambling, call the National Problem Gambling Helpline at 1-800-GAMBLER (1-800-426-2537) or visit ncpgambling.org.

**Contributors:** 
1. Ryan Harrington
2. Joshua Stevens 
3. Nicholas Harding

In [1]:
import sys
import tomllib
from pathlib import Path

In [2]:
# CONFIG_PATH = Path("public-fantast-football-analytics/config/config.toml")
CONFIG_PATH = Path("config/config.toml")

with CONFIG_PATH.open("rb") as f:
    config = tomllib.load(f)

from dotenv import load_dotenv
import pandas as pd
import altair as alt
import matplotlib.pyplot as plt
import plotly.graph_objects as go
from plotly.subplots import make_subplots
import warnings

warnings.filterwarnings("ignore")

sys.path.append("public-fantast-football-analytics")

from src.data_processing import utils_data_cleansing as utils
from src.data_viz import viz
from src.data_viz import viz_correlation_section
from src.data_processing import stats as stats

alt.renderers.enable("html");

## Introduction

Fantasy football is a game in which participants act as team managers. Each manager "drafts" a roster of real NFL players, taking turns picking from the same pool of players, much like picking teams on a playground. Each week, the players on a manager's roster earn points based on how they perform in their real NFL games, such as yards gained, touchdowns scored, and passes caught. A manager's team is scored against another manager's team each week, and the better score wins.

Week-to-week management matters, but the draft is where most of a team's strength is built. A strong draft provides consistent scoring every week and enough depth to absorb injuries to key players.

Most advice on who to draft comes from expert rankings and intuition or from average draft position (ADP), which simply shows where other managers usually pick a player. This analysis instead uses data to build a draft strategy.

**Key terms**

- **Positions:** Offensive players fall into four main groups. Quarterbacks (QB) throw the ball. Running backs (RB) carry it. Wide receivers (WR) and tight ends (TE) catch it.
- **Scoring format:** Leagues differ in how they award points for catches. In **PPR** (points per reception) leagues, a player earns 1 point for every catch on top of points for yards and touchdowns. In **non-PPR** (standard) leagues, catches earn nothing on their own. This one rule can change which players and positions are most valuable, so every analysis here is run under both formats.
- **Points per game:** The average number of fantasy points a player scores per game played. It is the main measure of player performance in this analysis.
- **Replacement level:** The score of the best player still available once every team has filled its starting lineup. It shows how much a top player is worth compared with an easily found alternative.

**Data**

The analysis combines NFL and college player statistics. The NFL data (sourced through the `nflreadpy` package) has one row per player per week for 2018–2025. The college data is summarized by season. Because the two sources are structured differently, the analysis focuses on NFL players who return season after season.

**Topics covered**

1. **Drivers of fantasy performance.** Which statistics are most closely tied to scoring across all offensive positions, and which positions produce them? (Key Finding #1)
2. **Position-specific drivers.** How do scoring patterns differ by position and scoring format, and do they hold from season to season? (Key Finding #2)
3. **Positional draft strategy.** In a standard 12-team league, which positions should be drafted first in each scoring format? (Key Finding #3)
4. **Player selection by position.** For each position, which statistics identify strong players, and does opportunity (how often a player gets the ball) or efficiency (how well they use it) better predict next season's production?
5. **Summary and recommendations.** What matters most, what is reliable, and what are the limitations?

The goal is a strategic framework for drafting: which positions to prioritize and which general traits to look for. It is not a list of players to pick.

## Contributions

**Ryan Harrington**: Ryan provided the foundation and structure for the entire project and took a leadership role, planning the work, delegating tasks, and keeping the group on track. He sourced and optimized the NFL data. Once the data was landed, he standardized it and built the framework for repeatable utility functions that shape the data for analysis. He also designed the unique key used to join the datasets. Throughout the project, Ryan kept the repository tidy so that all core components were easy to find and understand. During analysis, he assisted with visualization, debugged visuals, and caught inconsistencies that would otherwise have led to misleading findings.

- Led the project by planning, delegating, and keeping the group on track
- Sourced and optimized the NFL data
- Standardized the data and built reusable utility functions
- Designed the unique key for joining datasets
- Kept the repository organized and easy to navigate
- Debugged visuals and caught inconsistencies that would have produced misleading findings

**Joshua Stevens**: Joshua developed one of the most valuable tools in this project: the player-level dashboards. They played a major role in identifying which metrics deserved a deeper look, and they shaped the story told in this analysis. Exploring the dashboards by position led to the discovery that positional differences affect scoring, which became the basis for the position-specific analysis and draft strategy. He built scatterplots, correlation heatmaps, and histograms and turned each into a reusable function. This makes the analysis easier for a non-technical audience to follow and gives a technical audience a repeatable process to recreate it.

- Built the player-level dashboards
- Used the dashboards to uncover positional differences that affect scoring, which led to the position-specific analysis and draft strategy
- Created scatterplots, correlation heatmaps, and histograms as reusable functions
- Helped identify which metrics deserved deeper analysis
- Made the analysis accessible to non-technical audiences and repeatable for technical ones

**Nicholas Harding**: Nicholas shaped the narrative and consolidated the large volume of visualizations and insights into a cohesive, data-driven story. During the project proposal phase, he raised the ethical concern that this information could be used for gambling and proposed centering the analysis on trends rather than individual players. During the visualization phase, he refined visuals to make insights clearer. He limited correlation plots to strong correlations to reduce noise, and he created the decaying line plot that led to Key Finding #3, a strategic recommendation for draft strategy.

- Shaped the project narrative and consolidated insights into a cohesive story
- Raised the gambling ethical concern and proposed a trend-focused approach over individual players
- Refined visuals, including limiting correlation plots to strong correlations to reduce noise
- Created the decaying line plot behind Key Finding #3 (draft strategy recommendation)

## Data & Setup


For this project, we used two primary data sources, nflverse through the python nflreadpy package and the CollegeFootballData API via API key.  The nflverse dataset provides player statistics at the week level, which we aggregated to the season level for analysis.  This dataset has one row per player per week for 2018-2025.  The CollegeFootballData API provides college football data at the season level, which we normalized and joined to the NFL data via a join key of position-player-season (note this was a concat since the records are distinct as no one, at least currently. can play in the NFL and college for the same season).  We did the normalizations via mappings files in the mappings directory that are used by data processing utility functions in the src/data_processing/utils_data_cleansing.py file.  Because the two sources differ in grain, the analysis focuses on returning NFL players and measures efficiency in fantasy points per game. Every analysis is run under both PPR and non-PPR scoring, since the one-point-per-reception rule changes which players and positions are most valuable.  We also applied minimum thresholds on things like passing attempts, rush attempts, and receiving targets that are in our config file to filter out potential noise in the data due to low player samples.

# Load Data 

The grain of the data is two fold, NFL data is one row per player per week, while the college data is a season aggreate. As a result, we will need to primarily focus on returning NFL players when evualting efficency, which we will represent in points per week. 

In [3]:
# Load the combined player stats CSV file into a DataFrame
player_stats_df = pd.read_csv("data/combined_player_stats.csv")

# Split College and NFL stats into separate DataFrames
college_stats_df = player_stats_df[player_stats_df["data_source"] == "college_data"]
nfl_stats_df = player_stats_df[player_stats_df["data_source"] == "nflreadpy"]

In [4]:
# full PPR, all positions
all_ppr = stats.build_offense_season_agg(
    nfl_stats_df,
    groupby_cols=stats.all_player_cols,
    ppr=1,
    positions=stats.offensive_positions,
)
all_nonppr = stats.build_offense_season_agg(
    nfl_stats_df,
    groupby_cols=stats.all_player_cols,
    ppr=0,
    positions=stats.offensive_positions,
)

## Drivers of Fantasy Performance

This section looks at which variables correlate most strongly with fantasy points. 

Due to the limitations of the college data, this will be focused on returning NFL Players. 

- Players are intentionally not split by position here: the goal is to maximize points per week, not just to find position-specific patterns. 
- Pooling all positions shows which kinds of offensive production generate points most efficiently, and so which positions are the most efficient scorers overall.


**Definition:** Scoring Type
- PPR (points per reception): players earn 1 point for every catch, on top of yardage and touchdown points.
- Non-PPR (standard): catches earn no points on their own; only yardage and touchdowns count.

Throughout this analysis we wil be examining the data in both contexts as this single rule cand drastically affect how the game is played optimally. 

### Correlations 

The following visuals highlight moderate and strong correlations between statistics and player performance. 

In this first pass **we have not separated by posistion intentionally**. Before examining posistion specific performance drivers, we want to uncover high level trends which will provide the foundational strategy for selecting players. 

In [5]:
ppr_corr_bar_chart = viz.corr_bar_chart(
    all_ppr,
    "avg_fantasy_points",
    "Correlation with Avg Fantasy Points (PPR)",
    exclude=["fantasy_points"],
).properties(width=320, height=alt.Step(8))

nonppr_corr_bar_chart = viz.corr_bar_chart(
    all_nonppr,
    "avg_fantasy_points",
    "Correlation with Avg Fantasy Points (Non-PPR)",
    exclude=["fantasy_points"],
).properties(width=320, height=alt.Step(8))

# correlation of every numeric stat with the target, for each format
ppr_num = all_ppr.select_dtypes(include="number").copy()
nonppr_num = all_nonppr.select_dtypes(include="number").copy()

both = pd.DataFrame(
    {
        "PPR": ppr_num.drop(columns=["avg_fantasy_points", "fantasy_points"]).corrwith(
            ppr_num["avg_fantasy_points"]
        ),
        "Non-PPR": nonppr_num.drop(
            columns=["avg_fantasy_points", "fantasy_points"]
        ).corrwith(nonppr_num["avg_fantasy_points"]),
    }
).dropna()
both = both[(both.abs() >= 0.3).any(axis=1)].rename_axis("stat").reset_index()
both["difference"] = both["PPR"] - both["Non-PPR"]

difference_chart = (
    alt.Chart(both, title="Change in Correlation: PPR − Non-PPR")
    .mark_bar()
    .encode(
        x=alt.X("difference:Q", title="Δ r (PPR − Non-PPR)"),
        y=alt.Y("stat:N", sort="-x", title=None),
        color=alt.condition(
            "datum.difference > 0", alt.value("#2b6cb0"), alt.value("#dd6b20")
        ),
        tooltip=[
            "stat",
            alt.Tooltip("PPR:Q", format=".2f"),
            alt.Tooltip("Non-PPR:Q", format=".2f"),
            alt.Tooltip("difference:Q", format="+.2f"),
        ],
    )
    .properties(width=320, height=alt.Step(8))
)

((ppr_corr_bar_chart | nonppr_corr_bar_chart) & difference_chart).resolve_scale(
    color="independent"
).properties(
    title="Correlation with Average Fantasy Points per Game (weak correlations, |r| < 0.3, hidden)"
)

alt.VConcatChart(...)

### Which posistions do these statics belong to?

Scoring format clearly changes which positions matter most. 

Football fans may already know which positions produce these stats, but several positions often contribute to the same category, so the chart below shows how each stat's total is split by position.

In [6]:
TARGET = "avg_fantasy_points"
EXCLUDE = ["fantasy_points"]
POSITIONS = ["QB", "RB", "WR", "TE"]
COLORS = ["#2b6cb0", "#38a169", "#dd6b20", "#805ad5"]

rows = []
for fmt, df in [("PPR", all_ppr), ("Non-PPR", all_nonppr)]:
    num_cols = df.select_dtypes(include="number").columns.drop(
        [TARGET, *EXCLUDE], errors="ignore"
    )

    # top 10 stats by |r| with the target for this format
    corr = df[num_cols].corrwith(df[TARGET])
    top10 = corr.abs().nlargest(10).index

    # each position's share of each stat's total
    totals = (
        df.groupby("position")[list(top10)]
        .sum()
        .clip(lower=0)
        .reindex(POSITIONS)
        .fillna(0)
    )
    shares = totals / totals.sum()

    for stat in top10:
        start = 0
        for i, pos in enumerate(POSITIONS):
            share = shares.loc[pos, stat]
            rows.append(
                {
                    "format": fmt,
                    "stat": stat,
                    "position": pos,
                    "pos_order": i,
                    "share": share,
                    "start": start,
                    "end": start + share,
                    "mid": start + share / 2,
                    "correlation": corr[stat],
                }
            )
            start += share

stat_ownership = pd.DataFrame(rows)

y_sort = alt.EncodingSortField("correlation", op="max", order="descending")

bars = (
    alt.Chart()
    .mark_bar()
    .encode(
        x=alt.X(
            "start:Q",
            axis=alt.Axis(format="%"),
            title="Share of stat total",
            scale=alt.Scale(domain=[0, 1]),
        ),
        x2="end:Q",
        y=alt.Y("stat:N", title=None, sort=y_sort),
        color=alt.Color(
            "position:N",
            scale=alt.Scale(domain=POSITIONS, range=COLORS),
            title="Position",
        ),
        tooltip=[
            "format",
            "stat",
            "position",
            alt.Tooltip("share:Q", format=".0%"),
            alt.Tooltip("correlation:Q", format=".2f", title="r with target"),
        ],
    )
)

labels = (
    alt.Chart()
    .mark_text(color="white", fontSize=10, fontWeight="bold")
    .encode(
        x="mid:Q",
        y=alt.Y("stat:N", sort=y_sort),
        text=alt.Text("share:Q", format=".0%"),
    )
    .transform_filter(
        "datum.share >= 0.06"  # skip labels on slivers too narrow to fit text
    )
)

alt.layer(bars, labels, data=stat_ownership).properties(width=320, height=450).facet(
    column=alt.Column(
        "format:N",
        title=None,
        sort=["PPR", "Non-PPR"],
        header=alt.Header(labelFontSize=13),
    ),
).resolve_scale(y="independent").properties(
    title="Top 10 Stats by Correlation: Which Position Produces Them"
)

alt.FacetChart(...)

### **Key Finding #1** 

### The Most Important Statistics by Scoring Format

**PPR**: PPR players should focus on targeting the Wide Receiver posistion in drafts, as they own the largest share of 9/10 statistics with the highest correlations to fantasy points per game. 

**Non-PPR**: Non-PPR players should focus on targeting the Quarterback posistion in drafts, as they own the largest share of 9/10 statistics with the highest correlations to fantasy points per game. 



Now that we know which posistion is the most important, we need to rank all posisitions in order of performance. This will provide key strategic insights into how players of each scoring type should prioritize posistion groups. 

## Position-Specific Drivers

In [ ]:
alt.data_transformers.disable_max_rows()

POSITIONS = list(viz.POSITION_COLORS)
COLOR_SCALE = viz.POSITION_COLOR_SCALE
VALUE = "avg_fantasy_points"
SEASONS = None  # e.g. [2024] or list(range(2021, 2026)); None = all seasons

for label, df in [("PPR", all_ppr), ("Non-PPR", all_nonppr)]:
    x_title = f"Avg Fantasy Points per Game ({label})"

    # one row per player-season: average fantasy points per game
    data = (df.groupby(["player", "position", "season"], as_index=False)[VALUE].mean())[
        ["position", "season", VALUE]
    ].dropna()
    if SEASONS is not None:
        data = data[data["season"].isin(SEASONS)]

    # histogram: bars + count labels, one panel per position
    hist_base = alt.Chart().encode(
        x=alt.X(f"{VALUE}:Q", bin=alt.Bin(maxbins=30), title=x_title),
        y=alt.Y("count():Q", title="Player-Seasons"),
    )

    hist_bars = hist_base.mark_bar().encode(
        color=alt.Color("position:N", scale=COLOR_SCALE, legend=None)
    )
    hist_labels = hist_base.mark_text(dy=-5, fontSize=9).encode(text="count():Q")

    hist = (
        alt.layer(hist_bars, hist_labels, data=data)
        .properties(width=300, height=70)
        .facet(row=alt.Row("position:N", sort=POSITIONS, title=None))
        .resolve_scale(y="independent")
        .properties(title=f"Distribution of Player Averages ({label})")
    )

    # box plot: boxes + labels for the 25th percentile, median and 75th percentile
    box_base = alt.Chart(data).encode(y=alt.Y("position:N", sort=POSITIONS, title=None))

    box_marks = box_base.mark_boxplot(
        extent=1.5,
        size=28,
        median={"color": "white"},
        outliers={"size": 8, "opacity": 0.3},
    ).encode(
        x=alt.X(f"{VALUE}:Q", title=x_title),
        color=alt.Color("position:N", scale=COLOR_SCALE, legend=None),
    )

    stats = box_base.transform_aggregate(
        q1=f"q1({VALUE})",
        median=f"median({VALUE})",
        q3=f"q3({VALUE})",
        groupby=["position"],
    )
    median_labels = stats.mark_text(dy=-22, fontSize=10, fontWeight="bold").encode(
        x="median:Q", text=alt.Text("median:Q", format=".1f")
    )
    q1_labels = stats.mark_text(dy=24, fontSize=9, color="gray").encode(
        x="q1:Q", text=alt.Text("q1:Q", format=".1f")
    )
    q3_labels = stats.mark_text(dy=24, fontSize=9, color="gray").encode(
        x="q3:Q", text=alt.Text("q3:Q", format=".1f")
    )

    box = (box_marks + median_labels + q1_labels + q3_labels).properties(
        width=380, height=520, title=f"Spread of Player Averages ({label})"
    )

    display(
        (hist | box).properties(
            title=f"Average Fantasy Points per Game by Position ({label})"
        )
    )

alt.HConcatChart(...)

alt.HConcatChart(...)

**Early patterns in positional importance**

**Both scoring formats**
1. **QBs score the most.** Their median points per game is consistently higher than any skill position (RB, WR, TE).
2. **Usable QBs are plentiful.** QB averages follow a roughly normal distribution, so many quarterbacks deliver solid, consistent production. Because a starter is easy to find, drafting a QB early is likely less important than filling other positions.
3. **Good TEs are scarce.** TEs have the lowest averages, and few exceed 6 points per game. That makes most TEs a low-impact pick, and the rare productive ones especially valuable.

**PPR**
- Skill positions score more than in non-PPR, which narrows the gap with QBs. With starting QBs easy to find, **skill-position picks matter most.**

**Non-PPR**
- Skill positions average about 1.5 fewer points per game than in PPR, which widens the gap with QBs. **An elite QB may be more valuable in this format**, though further analysis is needed to confirm it.

Before ranking posistions by importance, we need to see if they are consistent over time. 

Are these findings tried and true patterns, or outlier driven?

In [8]:
alt.data_transformers.disable_max_rows()

POSITIONS = list(viz.POSITION_COLORS)
VALUE = "avg_fantasy_points"
STEP = 28  # height of each season's row
OVERLAP = 1.2  # how far each ridge rises into the row above

# one row per player-season, for each format
formats = {
    label: df.groupby(["player", "position", "season"], as_index=False)[VALUE].mean()
    for label, df in [("PPR", all_ppr), ("Non-PPR", all_nonppr)]
}

for pos in POSITIONS:
    pos_data = {
        label: ps.loc[ps["position"] == pos, ["season", VALUE]].dropna()
        for label, ps in formats.items()
    }

    # shared x-axis across both formats so they're directly comparable
    x_max = float(max(d[VALUE].quantile(0.99) for d in pos_data.values()))
    x_scale = alt.Scale(domain=[0, x_max])

    panels = []
    for label, data in pos_data.items():
        # distribution ridges
        ridges = (
            alt.Chart()
            .transform_filter(alt.datum[VALUE] <= x_max)
            .transform_density(
                VALUE,
                groupby=["season"],
                as_=[VALUE, "density"],
                extent=[0, x_max],
                steps=100,
            )
            .transform_joinaggregate(max_density="max(density)", groupby=["season"])
            .transform_calculate(
                scaled="datum.density / datum.max_density"  # every ridge peaks at the same height
            )
            .mark_area(
                interpolate="monotone",
                fillOpacity=0.75,
                stroke="white",
                strokeWidth=0.8,
                color=viz.POSITION_COLORS[pos],
            )
            .encode(
                x=alt.X(
                    f"{VALUE}:Q",
                    title=f"Avg Fantasy Pts / Game ({label})",
                    scale=x_scale,
                ),
                y=alt.Y(
                    "scaled:Q",
                    axis=None,
                    scale=alt.Scale(range=[STEP, -STEP * OVERLAP]),
                ),
                tooltip=["season"],
            )
        )

        # median marker + label per season
        medians = alt.Chart().transform_aggregate(
            median=f"median({VALUE})", groupby=["season"]
        )

        median_rule = medians.mark_rule(
            color="black", strokeWidth=1.5, strokeDash=[3, 2]
        ).encode(
            x=alt.X("median:Q", scale=x_scale),
            y=alt.value(STEP),
            y2=alt.value(-STEP * 0.6),
            tooltip=[
                "season",
                alt.Tooltip("median:Q", format=".1f", title="Median pts/game"),
            ],
        )
        median_label = medians.mark_text(
            align="left", dx=4, dy=-4, fontSize=10, fontWeight="bold"
        ).encode(
            x=alt.X("median:Q", scale=x_scale),
            y=alt.value(STEP),
            text=alt.Text("median:Q", format=".1f"),
        )

        panels.append(
            alt.layer(ridges, median_rule, median_label, data=data)
            .properties(
                width=380,
                height=STEP,
            )
            .facet(
                row=alt.Row(
                    "season:O",
                    title=None,
                    header=alt.Header(
                        labelAngle=0, labelAlign="left", labelFontSize=11
                    ),
                ),
                spacing=0,
            )
            .properties(title=label, bounds="flush")
        )

    display(
        alt.hconcat(*panels, spacing=30)
        .properties(
            title=f"{pos}: Distribution of Avg Fantasy Points per Game by Season"
        )
        .configure_view(stroke=None)
    )

alt.HConcatChart(...)

alt.HConcatChart(...)

alt.HConcatChart(...)

alt.HConcatChart(...)

### Key Finding #2: 

### Positional Importance Differs by Scoring Format 

**Relevant to Both Formats**
- **RBs and WRs outscore TEs.** TEs are tied to more of the high-correlation stats as their offensive responsibilities similar to Wide Receivers , but RBs score more points per game.
- **Productive RBs are easier to find than productive TEs.** More RBs make consistent contributions, so drafting a useful RB is more likely than drafting a useful TE.
- **QBs provide consistent scoring, but are plentiful.** They have the highest average points per game, but the distribution indicates that there are no shortage of safe options.

**PPR**
- **WRs produce most of the stats that drive scoring.** They account for the largest share of the stats most correlated with points per game.
- **WRs and RBs lead the skill positions in scoring.** Their average points per game are roughly tied.
- **WRs have a higher floor than RBs.** Their 25th-percentile scoring is higher, so even lower-end WRs contribute more reliably.

**Non-PPR**
- **QBs dominate the stats that drive scoring.** They hold the largest share of 9 of the 10 stats most correlated with points per game, making QB much more important in this format. 

While this context is helpful, we want to go one level deeper and suggest a strategy around which posistions to target first by scoring format, ranked by urgency. 

**Methodology**
- **Data:** NFL regular-season weekly stats, 2018–2025 (2026 excluded as a partial season), limited to QB, RB, WR and TE players with at least 6 games in a season.
- **Per-game scoring:** each player's average fantasy points per game for the season, computed separately for PPR and non-PPR scoring.
- **Positional rank:** players are ranked within their position each season by points per game (1 = best), then the score at each rank is averaged across seasons. Each point therefore represents a *typical* Nth-best player, not a specific player.
- **Replacement level:** the first non-starter at each position, assuming a 12-team league, every team must start a specific number of players at each posision. EX: If league has two wide receiver slots per team, and there are 12 teams, this would be the 25th ranked receiver.  
- **Value over replacement:** each rank's points per game minus its position's replacement level. Higher values and steeper curves mean bigger gains from drafting that position early.

## Positional Draft Strategy

In [9]:
POSITIONS = list(viz.POSITION_COLORS)
COLOR_SCALE = viz.POSITION_COLOR_SCALE
STARTERS = {
    "QB": 12,
    "RB": 24,
    "WR": 24,
    "TE": 12,
}  # Required starters for a 12-team league: 1 QB, 2 RB, 2 WR, 1 TE
MAX_RANK = 40  # Plot the top N positional ranks
MIN_GAMES = 6  # Remove players with fewer than this many games

# positions sharing a replacement rank (e.g. QB13 and TE13) get stacked label slots so they don't overlap
LABEL_SLOT, taken = {}, {}
for pos in POSITIONS:
    LABEL_SLOT[pos] = taken.get(STARTERS[pos], 0)
    taken[STARTERS[pos]] = LABEL_SLOT[pos] + 1

rows = []
for label, df in [("PPR", all_ppr), ("Non-PPR", all_nonppr)]:
    weekly = df[df["position"].isin(POSITIONS)]

    # aggregate week -> player-season
    ps = weekly.groupby(["player", "position", "season"], as_index=False).agg(
        games=("week", "nunique"), avg_fantasy_points=("fantasy_points", "mean")
    )
    ps = ps[ps["games"] >= MIN_GAMES]

    # rank within position and season (1 = best)
    ps["pos_rank"] = ps.groupby(["season", "position"])["avg_fantasy_points"].rank(
        ascending=False, method="first"
    )

    # average points at each positional rank across seasons
    curve = ps.groupby(["position", "pos_rank"], as_index=False)[
        "avg_fantasy_points"
    ].mean()

    # replacement level = first player past the starters
    repl = curve[curve["pos_rank"] == curve["position"].map(STARTERS) + 1].set_index(
        "position"
    )["avg_fantasy_points"]
    curve["above_replacement"] = curve["avg_fantasy_points"] - curve["position"].map(
        repl
    )

    # flag and label the replacement-level rank for each position (e.g. "RB25: 12.3 pts/g")
    curve["is_repl"] = curve["pos_rank"] == curve["position"].map(STARTERS) + 1
    curve["repl_label"] = (
        curve["position"]
        + curve["pos_rank"].astype(int).astype(str)
        + ": "
        + curve["avg_fantasy_points"].map("{:.1f}".format)
        + " pts/g"
    )
    curve["label_slot"] = curve["position"].map(LABEL_SLOT)

    curve["format"] = label
    rows.append(curve[curve["pos_rank"] <= MAX_RANK])

curves = pd.concat(rows, ignore_index=True)

base = alt.Chart().encode(
    x=alt.X(
        "pos_rank:Q",
        title="Positional rank (1 = best at position)",
        scale=alt.Scale(domain=[1, MAX_RANK]),
    ),
    y=alt.Y("above_replacement:Q", title="Pts / game above replacement"),
    color=alt.Color("position:N", scale=COLOR_SCALE, sort=POSITIONS, title="Position"),
)

lines = base.mark_line(point=alt.OverlayMarkDef(size=20)).encode(
    tooltip=[
        "format",
        "position",
        alt.Tooltip("pos_rank:Q", title="Rank"),
        alt.Tooltip("avg_fantasy_points:Q", format=".1f", title="Pts / game"),
        alt.Tooltip("above_replacement:Q", format="+.1f", title="Above replacement"),
    ],
)

# replacement level: diamond marker + label (stacked where positions share a rank)
repl_points = (
    base.transform_filter(alt.datum.is_repl)
    .mark_point(
        shape="diamond",
        size=140,
        filled=True,
        stroke="black",
        strokeWidth=1,
        opacity=1,
    )
    .encode(
        tooltip=[
            "format",
            "position",
            alt.Tooltip("pos_rank:Q", title="Replacement rank"),
            alt.Tooltip(
                "avg_fantasy_points:Q", format=".1f", title="Replacement pts / game"
            ),
        ],
    )
)
repl_labels = [
    base.transform_filter((alt.datum.is_repl) & (alt.datum.label_slot == slot))
    .mark_text(
        align="left",
        dx=8,
        dy=-14 + 16 * slot,
        fontSize=10,
        fontWeight="bold",
    )
    .encode(text="repl_label:N")
    for slot in sorted(set(LABEL_SLOT.values()))
]

zero = alt.Chart().mark_rule(color="gray", strokeDash=[4, 4]).encode(y=alt.datum(0))

alt.layer(zero, lines, repl_points, *repl_labels, data=curves).properties(
    width=500, height=450
).facet(
    column=alt.Column(
        "format:N",
        sort=["PPR", "Non-PPR"],
        title=None,
        header=alt.Header(labelFontSize=13),
    ),
).properties(
    title="Positional Drop-off: Points per Game Above Replacement (◆ = replacement level)"
)

alt.FacetChart(...)

### Key Finding #3: Ranking Positions by Draft Priority

Positions are ranked by how much the best player at each position outscores a replacement level player in points per game. A bigger gap means waiting on that position costs more.

**PPR**
1. **Running Back:** +11.7 pts/game
   - WRs produce the largest share of high-correlation stats, but RBs drop off more steeply, so elite RBs are harder to replace and should be drafted first.
2. **Wide Receiver:** +10.1 pts/game
3. **Tight End:** +8.3 pts/game
4. **Quarterback:** +7.6 pts/game

**Non-PPR**
1. **Running Back:** +10.1 pts/game
   - QBs produce the largest share of high-correlation stats, but RBs drop off more steeply, so elite RBs remain the top priority.
2. **Quarterback:** +7.6 pts/game
3. **Wide Receiver:** +6.7 pts/game
4. **Tight End:** +5.5 pts/game

This provides a strategic framework for fantasy players to approach how they should select their team. 

While the blueprint is helpful, it doesn't help us to identify which players to take. Given the ethical concern we raised above, we will refrain from providing specifc player recommendations and instead provide analysis to highlight general statstics that players use to choose optimal players at each posistion. 

## Player Selection by Posistion 

### Correlations

Only correlations with |r| ≥ 0.3 are shown, to focus on the most impactful features.

Stats that are part of the scoring formula itself, such as receiving yards and touchdowns, are excluded. They correlate with fantasy points by definition, so including them would show what *produces* points rather than what *drives* a player to score them.

In [10]:
POSITIONS = list(viz.POSITION_COLORS)
MIN_CORR = 0.3

# columns that are IDs, time, or the target itself in another form
EXCLUDE = [
    # bookkeeping / target variants
    "avg_fantasy_points",
    "fantasy_points_ppr",
    "total_games_played",
    "season",
    "week",
    # touchdowns
    "passing_tds",
    "rushing_tds",
    "receiving_tds",
    # yards that score points (and their per-game versions)
    "passing_yards",
    "rushing_yards",
    "receiving_yards",
    "pass_yards_per_game",
    "rush_yards_per_game",
    "rec_yards_per_game",
    # receptions (worth 1 point each in PPR)
    "receptions",
    # 2-point conversions
    "passing_2pt_conversions",
    "rushing_2pt_conversions",
    "receiving_2pt_conversions",
]

pairs = []
for pos in POSITIONS:
    ppr_chart = viz.targeted_heatmap(
        all_ppr[all_ppr["position"] == pos],
        ["fantasy_points"],
        title="PPR",
        exclude=EXCLUDE,
        min_corr=MIN_CORR,
    ).properties(width=70, height=300)

    nonppr_chart = viz.targeted_heatmap(
        all_nonppr[all_nonppr["position"] == pos],
        ["fantasy_points"],
        title="Non-PPR",
        exclude=EXCLUDE,
        min_corr=MIN_CORR,
    ).properties(width=70, height=300)
    pairs.append((ppr_chart | nonppr_chart).properties(title=pos))

alt.vconcat(
    alt.hconcat(pairs[0], pairs[1], spacing=25),
    alt.hconcat(pairs[2], pairs[3], spacing=25),
    spacing=40,
).properties(
    title=f"Stats Correlated with Fantasy Points by Position (|r| ≥ {MIN_CORR})"
)

alt.VConcatChart(...)

## Selecting QBs

In [11]:
qb_season_agg = pd.read_csv("data/qb_season_agg.csv")

# Create Filters

In [12]:
# create lists for filters
season_list = config["GLOBAL_SEASONS_LIST"]
player_list = qb_season_agg["player"].unique().tolist()

# create season filter
season_filter = viz.season_filter
data_source_filter = viz.data_source_filter

bar_chart_passing_yards = (
    (
        alt.Chart(qb_season_agg)
        .mark_bar()
        .encode(
            x=alt.X("player:N", title="Player Name"),
            y=alt.Y("passing_yards:Q", title="Passing Yards"),
            color=alt.Color("season:N", title="Season"),
            tooltip=[
                "player",
                "season",
                "passing_yards",
                "passing_tds",
                "passing_interceptions",
                "completion_percentage",
                "passing_yards_per_game",
            ],
        )
        .add_params(season_filter, data_source_filter)
        .transform_filter(alt.datum.season == season_filter)
        .transform_filter(alt.datum.data_source == data_source_filter)
    )
    .properties(title="Passing Yards by Player and Season")
    .interactive()
)

mean_passing_yards_line = (
    alt.Chart(qb_season_agg)
    .transform_filter(alt.datum.season == season_filter)
    .transform_calculate(statistic="'Mean Passing Yards'")
    .mark_rule(strokeWidth=2)
    .encode(
        y=alt.Y("mean(passing_yards):Q", title="Mean Passing Yards"),
        color=alt.Color(
            "statistic:N", scale=alt.Scale(domain=["Mean Passing Yards"], range=["red"])
        ),
    )
)

chart = (bar_chart_passing_yards + mean_passing_yards_line).resolve_scale(
    color="independent"
)

chart

alt.LayerChart(...)

In [13]:
# boxplot for passing yards by season
boxplot_passing_yards = (
    alt.Chart(qb_season_agg[qb_season_agg['total_games_played'] >= 6])
    .mark_boxplot()
    .encode(
        x=alt.X("season:N", title="Season"),
        y=alt.Y("passing_yards:Q", title="Passing Yards"),
        color=alt.Color("season:N", title="Season"),
    )
    .properties(width=750, height=100, title="Passing Yards by Season")
)

boxplot_passing_yards

alt.Chart(...)

An interesting note that this boxplot shows the average passing yards per season to be decreasing for quarterbacks that play a minimum of 6 games. 

In [14]:
# heatmap of correlations
corr = (
    qb_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

qb_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — QB Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

qb_heatmap

alt.Chart(...)

In [15]:
qb_dashboard_df = viz.apply_agg_dashboard_filters(
    qb_season_agg, config["season_agg_filters"]["qb"]
)

qb_dashboard = viz.build_qb_dashboard(qb_dashboard_df)
out_path = "qb_dashboard.html"
qb_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")
qb_dashboard

Saved dashboard to qb_dashboard.html


alt.VConcatChart(...)

In [16]:
rb_season_agg = pd.read_csv("data/rb_season_agg.csv")
wr_season_agg = pd.read_csv("data/wr_season_agg.csv")
te_season_agg = pd.read_csv("data/te_season_agg.csv")

In [17]:
# validate for the _correlation_block function that only nfl players are used: qb_season_agg
qb_season_agg_nfl = qb_season_agg[qb_season_agg["data_source"] == "nflreadpy"]
rb_season_agg_nfl = rb_season_agg[rb_season_agg["data_source"] == "nflreadpy"]
wr_season_agg_nfl = wr_season_agg[wr_season_agg["data_source"] == "nflreadpy"]
te_season_agg_nfl = te_season_agg[te_season_agg["data_source"] == "nflreadpy"]

In [18]:
viz_correlation_section.chart_opportunity_vs_efficiency_by_position(
    {
        "QB": qb_season_agg_nfl,
        "RB": rb_season_agg_nfl,
        "WR": wr_season_agg_nfl,
        "TE": te_season_agg_nfl,
    }
)

alt.FacetChart(...)

Efficiency matters from one year to the next more than opportunities. So quarterbaks who play better are more likely to still play well the next year and contribute in fantasy compared to the amount of opportunities they get.

In [19]:
viz_correlation_section._correlation_block(qb_season_agg_nfl, "QB")

alt.VConcatChart(...)

Highest correlation: EPA per pass attempt

Second highest: First downs per game

This points us in the direction that QB efficiency per pass attempt is more important than simply volume.


In [20]:
viz.qb_chart_efficiency(qb_season_agg_nfl[qb_season_agg_nfl["attempts"] >= 50])

alt.Chart(...)

This chart is showing the relationship between the completion percentage over expectation and passing EPA. Completion percentage over expectation is a statistic that compares completion percentage to the probabiltiy the catch is made by the receiver. Passing EPA measures the net value a quarterback adds to their team scoring points from the start of that play to the end. For instance, completing a pass to gain a first down on 3rd and 3 has a higher EPA than a pass completed short of a first down when it is 3rd and 3. 

Look to target quartbacks with high efficiency comapred to quarterbacks with high volume, but low efficiency metrics.

### Selecting WRs

In [21]:
corr = (
    wr_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

wr_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — WR Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

wr_heatmap

alt.Chart(...)

In [22]:
viz_correlation_section._correlation_block(wr_season_agg_nfl, "WR")

alt.VConcatChart(...)

Highest correlation: first downs per game (0.96)

Second highest: targets per game (0.93)

Wide receiver opportunity from one year to the next correlates more to fantasy production that efficiency.

In [23]:
wr_dashboard_df = viz.apply_agg_dashboard_filters(
    wr_season_agg, config["season_agg_filters"]["wr"]
)

wr_dashboard = viz.build_wr_dashboard(wr_dashboard_df)
out_path = "wr_dashboard.html"
wr_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")

wr_dashboard

Saved dashboard to wr_dashboard.html


alt.VConcatChart(...)

#### Target Share vs Receiving Yards 

Wide receivers need to get the ball to score points. Players that have a higher target share on the team have more oportunity to catch the ball and gain receiving yards. Our chart shows a positive correlation and even shows a positive correlation in total touchdowns. 

When targeting wide receivers, you should look for players who are target hogs and have a large target share on their team. Targets are also 'sticky' and correlate to future year success. Also, finding players who get down field and convert first downs will improve your chances of finding a valuable player.

### Selecting TEs

In [24]:
viz_correlation_section._correlation_block(te_season_agg_nfl, "TE")

alt.VConcatChart(...)

Highest correlation: first downs per game (0.96)

Second highest: targets per game (0.92)

Tight end opportunity from one year to the next correlates more to fantasy production that efficiency.

In [25]:
te_dashboard_df = viz.apply_agg_dashboard_filters(
    te_season_agg, config["season_agg_filters"]["te"]
)

te_dashboard = viz.build_te_dashboard(te_dashboard_df)
out_path = "te_dashboard.html"
te_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")

te_dashboard

Saved dashboard to te_dashboard.html


alt.VConcatChart(...)

#### Target Share vs Receiving Yards 

Target share is even more important as very few score more than 7 points per game on average. The same logic as with wide receivers applies here. The more targets you get, the more points you will score. Finding a solid tight end from a limited supply is difficult and points to the idea of obtaining a stud tight end early, and finding one later in the draft or on free agency much more difficult.

Target a tight end who commands a large target share and has the abiltiy for yards after the catch to gain first downs. 

### Selecting RBs

In [26]:
# boxplot for rushing yards by season
boxplot_rushing_yards = (
    alt.Chart(rb_season_agg[rb_season_agg['total_games_played'] >= 6])
    .mark_boxplot()
    .encode(
        x=alt.X("season:N", title="Season"),
        y=alt.Y("rushing_yards:Q", title="Rushing Yards"),
        color=alt.Color("season:N", title="Season"),
    )
    .properties(width=750, height=100, title="Rushing Yards by Season")
)

boxplot_rushing_yards

alt.Chart(...)

Looking at rush yards per season it looks like on average the amount of rush yards per player is increasing. This corresponds to passing yards decreasing as shown in an earlier visual.

In [27]:
viz_correlation_section._correlation_block(rb_season_agg_nfl, "RB")

alt.VConcatChart(...)

Workload for runningbacks is more important than efficiency. With in one season workload has a correlation of 0.91 compared to efficiency at 0.23. Also, in the year following opportunity has a r value of 0.56 compared to efficiency at 0.17.

Highest Correlation: touches per game

Second highest: rushing first downs per game

Target runningbacks who see a lot of carries and receptions that also have the ability to gain first downs and big plays.

In [28]:
rb_dashboard_df = viz.apply_agg_dashboard_filters(
    rb_season_agg, config["season_agg_filters"]["rb"]
)

rb_dashboard = viz.build_rb_dashboard(rb_dashboard_df)
out_path = "rb_dashboard.html"

rb_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")
rb_dashboard

Saved dashboard to rb_dashboard.html


alt.VConcatChart(...)

More involvement means more oppotunities to gain yards and score touchdowns. A runningback who sees more carries will be more beneficial to your team than one who sees minimal usage per game. Also, a runningback who is involved in the receiving game will score more points, especially in PPR leagues comapres to half or non PPR leagues.

The workload vs efficiency chart shows the relationship that more carries lead to more touchdowns (size of the point) and that yards per carry (efficiency) is not as important. There are many runningbacks who gain 4 yards per carry or more, but do not see a lot of carries that are not relevent to helping your fantasy team.

### Key Findings Summary & Recommendations

# QBs

Our analysis has found that from year to year, quarterback efficieny is more indicative than pure volume. This means that when prepping for a fantasy football draft you should weight efficient quartbacks more than a worse quartberack who might project to throw the ball more. It was also found that EPA per pass attempt and first downs per game were correlated the most to fantasy points wirh r values of 0.78 and 0.76 respectively. 

# WRs

For wide receivers, we found that opportunity was more correlated to fantasy production in the next year than efficiency. Opportunity in the current year has an r value of 0.93 and the next year 0.64. Meanwhile, efficiency had an r value of 0.44 in the current year and 0.29 the next year. We also found that within a season the two metics that correspond to fantasy points the most were first downs per game (0.96) and targets per game (0.92). This tells us we want to target wide receivers that can get diwn field and also demand more targets than their fellow teammates. 


# TEs

For tight ends, we found that from one year to the next opportunity was more important that efficiency. With oppotunities in the same year having a r value of 0.92 and the next year 0.61. While at the same time efficiency was at 0.39 and the next year 0.34. TIn a single season, the two key metrics were first downs per game (0.96) and targets per game (0.92). This tells us we want to target tight ends that command more targets per game and have the ability for yards after the catch to gain those first downs. Since most teams utilize only one tight end and many teams do not run an offensive scheme that features a tight end heavily, it is beneficial to draft a tight end that commands a larger target share and is on an offense that utilizes them more.

# RBs

For runnning backs, opportunities matter more than efficiency. From year to year, opportunities correlated more to fantasy output than efficiency with r values of 0.91 to 0.56 the next year for opportunites and 0.23 to 0.17 for efficiency. We found that touches per game (0.91) and rushing first downs(0.84) were the two key metrics that correlated the most to fantasy points. This also tells us when drafting or looking for a player to pick up, you should value total opportunities and runningbacks that are relied on to get first downs for their team. 